# Lấy 10 bài cho mỗi domain để đánh giá độ sạch của Crawl4AI — chạy local

Giữ nguyên cấu hình browser, fast/protected/slow, pruning `dynamic=0.6`,
HTML → Markdown, FIT → RAW fallback và phân loại lỗi của notebook gốc.
Không có Kaggle, Google Drive, chia worker hoặc lịch sử crawl toàn corpus.

**Cách chạy:** cấu hình `DOMAINS_FILE` ở mục 2 rồi chạy lần lượt các cell.
rồi chạy lần lượt các cell. Máy cần Internet, Python 3.10+ và Chromium của Crawl4AI.
Nếu Crawl4AI đã được cài và chạy được, bỏ qua cell cài đặt.

URL được lấy từ **corpus `AIGuruTinix/ViBioMIR` như notebook gốc**.
Notebook chỉ quét danh sách URL một lần để chọn mẫu; không crawl toàn corpus.
Mỗi domain giữ tối đa 30 URL thật làm ứng viên, crawl đến khi có 10 kết quả
thành công hoặc hết ứng viên. Với đúng 97 domain và đủ kết quả thành công,
`dataset.jsonl` có 970 dòng. Notebook không phân chia hoặc so khớp URL pattern.
Nếu thiếu, notebook báo số thiếu, không lặp bài hay tạo dòng giả.

`success=True` giữ đúng nghĩa của notebook gốc: crawl được Markdown và không
phát hiện trang chặn. **Đây chưa phải nhãn “nội dung sạch” hoặc “đúng bài viết”.**
LLM sẽ đánh giá điều đó sau. Log tất cả lần thử giúp thấy các domain khó crawl.

## 1. Cài đặt local (chỉ cần lần đầu)

In [1]:
%pip install -q -U crawl4ai datasets tqdm pandas
!crawl4ai-setup



[notice] A new release of pip is available: 25.3 -> 26.2.1
[notice] To update, run: /opt/homebrew/opt/python@3.10/bin/python3.10 -m pip install --upgrade pip
Note: you may need to restart the kernel to use updated packages.
[INIT].... → Running post-installation setup... 
[INIT].... → Installing Playwright browsers... 
182.1 MiB [                    ] 0% 0.0s182.1 MiB [                    ] 0% 748.7s182.1 MiB [                    ] 0% 591.8s182.1 MiB [                    ] 0% 544.3s182.1 MiB [                    ] 0% 514.1s182.1 MiB [                    ] 0% 489.4s182.1 MiB [                    ] 0% 482.4s182.1 MiB [                    ] 0% 473.1s182.1 MiB [                    ] 0% 459.9s182.1 MiB [                    ] 0% 727.7s182.1 MiB [                    ] 0% 611.7s182.1 MiB [                    ] 0% 581.2s182.1 MiB [                    ] 0% 542.1s182.1 MiB [                    ] 0% 510.3s182.1 MiB [                    ] 0% 511.2s182.1 MiB [                    ] 0% 490.5s182.1 Mi

## 2. Cấu hình và đọc danh sách 97 domain

Notebook mặc định đọc mảng `domains` trong `domain_profiles.json` và chỉ sử dụng trường `domain`.
Các trường `templates`, `url_pattern` và thông tin profiling khác được bỏ qua hoàn toàn:

```json
{
  "domains": [
    {"domain": "cnkang.com", "templates": [...]},
    {"domain": "vinmec.com", "templates": [...]}
  ]
}
```

`domain` khớp hostname sau khi bỏ `www.` và lowercase; không tự gộp subdomain khác.
Mỗi URL chỉ thuộc đúng domain của nó. Chọn mẫu bằng hash + seed để có kết quả
ổn định và tránh chỉ lấy 10 URL đầu corpus.

In [2]:
import json
import re
import heapq
import hashlib
import csv
from pathlib import Path
from collections import defaultdict, deque
from urllib.parse import urlsplit, urlparse
from datetime import datetime, timezone
from importlib.metadata import version
from tqdm.auto import tqdm

DOMAINS_FILE = Path("/Volumes/security/lucraft@lucraftmeds/lucraftmeds@notebooks/data-creation/domains-analyzation/domain_profiling_output/domain_profiles.json")
OUTPUT_DIR = Path("domain_cleanliness")
SAMPLES_PER_DOMAIN = 10
CANDIDATES_PER_DOMAIN = 30                 # Bao gồm 10 mẫu chính + URL dự phòng.
SEED = 42
MAX_CONCURRENCY = 3                        # Số trang chạy đồng thời trên máy local.
MEMORY_THRESHOLD_PERCENT = 80.0
DATASET_ID = "AIGuruTinix/ViBioMIR"
DATASET_CONFIG = "corpus"

PROTECTED_DOMAINS = {
    'special.vietnamplus.vn',
    'cnkang.com',
    '120ask.com',
    'familydoctor.com.cn',
    'ask.39.net',
    'vov2.vov.vn',
    'a-hospital.com',
    'suckhoecongdongonline.vn',
    'zhongyibaodian.net',
    'suckhoecongdongonline.vn',
    'zydcd.com',
    'thanhnien.vn',
    'wujue.com',
    'youlai.cn',
    'vov.vn',
    'zysjonline.com',
    'pmc-ecm-healthblog.beta.pharmacity.io',
    'nhathuoclongchau.com.vn',
    'giadinhonline.vn',
    'ask.familydoctor.com.cn',
}

SLOW_DOMAINS = {
    'bachmai.gov.vn',
    'wujue.com',
    'test.pmphai.com',
    'qihuangzhishu.com',
    'woman.39.net',
    'tnb.39.net',
    'wei.39.net',
    'shen.39.net',
    'baidu.com',
    'sj.39.net',
    'v.familydoctor.com.cn',
    'yanglao.familydoctor.com.cn',
    'ypk.familydoctor.com.cn',
    'baothanhhoa.vn',
    
}

if SAMPLES_PER_DOMAIN <= 0 or CANDIDATES_PER_DOMAIN < SAMPLES_PER_DOMAIN:
    raise ValueError("Cần 0 < SAMPLES_PER_DOMAIN <= CANDIDATES_PER_DOMAIN.")
if MAX_CONCURRENCY <= 0:
    raise ValueError("MAX_CONCURRENCY phải lớn hơn 0.")

def write_json(path, value):
    path.parent.mkdir(parents=True, exist_ok=True)
    temporary = path.with_name(path.name + ".tmp")
    temporary.write_text(json.dumps(value, ensure_ascii=False, indent=2), encoding="utf-8")
    temporary.replace(path)

def load_domains(path):
    payload = json.loads(path.read_text(encoding="utf-8-sig"))
    groups = payload.get("domains") if isinstance(payload, dict) else payload
    if not isinstance(groups, list) or not groups:
        raise ValueError("File domain phải là một list JSON không rỗng.")
    domains, seen = [], set()
    for group in groups:
        if not isinstance(group, dict):
            raise ValueError("Mỗi phần tử phải là object có trường domain.")
        domain = group.get("domain", "")
        if not isinstance(domain, str):
            raise ValueError("domain phải là chuỗi.")
        domain = domain.strip().lower().removeprefix("www.")
        if not domain or any(char in domain for char in "/:*?# "):
            raise ValueError(f"domain chỉ chứa hostname, không chứa scheme/path: {domain!r}")
        if domain in seen:
            raise ValueError(f"Domain bị lặp: {domain}")
        seen.add(domain)
        domains.append({"domain_id": f"d{len(domains) + 1:03d}", "domain": domain})
    return domains

domains = load_domains(DOMAINS_FILE)
OUTPUT_DIR.mkdir(parents=True, exist_ok=True)
TARGET_ROWS = len(domains) * SAMPLES_PER_DOMAIN
print(f"{len(domains)} domain × {SAMPLES_PER_DOMAIN} bài = mục tiêu {TARGET_ROWS:,} dòng.")
if len(domains) != 97:
    raise ValueError(f"Cần đúng 97 domain, nhưng file có {len(domains)} domain.")


97 domain × 10 bài = mục tiêu 970 dòng.


/opt/homebrew/lib/python3.10/site-packages/tqdm/auto.py:21: TqdmWarning: IProgress not found. Please update jupyter and ipywidgets. See https://ipywidgets.readthedocs.io/en/stable/user_install.html
  from .autonotebook import tqdm as notebook_tqdm


## 3. Chọn URL thật cho từng domain

Lần đầu quét hết cột URL của corpus bằng streaming và chỉ giữ tối đa
`CANDIDATES_PER_DOMAIN` URL khác nhau cho mỗi domain trong RAM. Không dừng ở
10 URL đầu tiên. Hash nhỏ nhất được giữ lại; seed cố định cho kết quả lặp lại.
`matched_source_rows` đếm dòng corpus thuộc domain, có thể bao gồm URL trùng trong nguồn.

Lưu `selected_urls.json` để những lần sau không phải quét lại. Nếu đổi danh sách domain,
seed hoặc số ứng viên, hãy chọn `OUTPUT_DIR` mới để giữ kết quả cũ.
Quét vài triệu dòng có thể mất thời gian và vẫn dùng băng thông của dataset.

In [3]:
from datasets import load_dataset

def select_candidates(rows, domains, capacity, seed):
    domain_indexes = {spec["domain"]: index for index, spec in enumerate(domains)}
    heaps = [[] for _ in domains]
    selected = [set() for _ in domains]
    counts = [0] * len(domains)

    for row in tqdm(rows, desc="Quét URL để chọn mẫu", unit="URL"):
        url = row.get("url")
        if not isinstance(url, str) or not url.strip():
            continue
        url = url.strip()
        try:
            parsed = urlsplit(url)
            domain = (parsed.hostname or "").lower().removeprefix("www.")
        except ValueError:
            continue
        if parsed.scheme not in {"http", "https"} or domain not in domain_indexes:
            continue
        score = int.from_bytes(hashlib.sha256(f"{seed}:{url}".encode()).digest()[:8], "big")
        entry = (-score, url, str(row.get("id", "")))
        index = domain_indexes[domain]
        counts[index] += 1
        if url in selected[index]:
            continue
        heap = heaps[index]
        if len(heap) < capacity:
            heapq.heappush(heap, entry)
            selected[index].add(url)
        elif entry > heap[0]:
            removed = heapq.heapreplace(heap, entry)
            selected[index].remove(removed[1])
            selected[index].add(url)

    return [{**spec, "matched_source_rows": counts[index],
             "candidates": [{"url": url, "id": doc_id}
                            for _, url, doc_id in sorted(heaps[index], reverse=True)]}
            for index, spec in enumerate(domains)]

selection_settings = {"domains": domains, "dataset": DATASET_ID,
                      "config": DATASET_CONFIG, "split": "train",
                      "seed": SEED, "capacity": CANDIDATES_PER_DOMAIN}
selection_path = OUTPUT_DIR / "selected_urls.json"
if selection_path.exists():
    selection = json.loads(selection_path.read_text(encoding="utf-8"))
    if selection["settings"] != selection_settings:
        raise ValueError("Cấu hình chọn mẫu đã đổi. Chọn OUTPUT_DIR mới rồi chạy lại.")
    domain_samples = selection["domains"]
    print("Dùng lại danh sách URL đã chọn.")
else:
    source = load_dataset(DATASET_ID, DATASET_CONFIG, split="train", streaming=True)
    domain_samples = select_candidates(source, domains, CANDIDATES_PER_DOMAIN, SEED)
    selection = {"settings": selection_settings, "domains": domain_samples}
    write_json(selection_path, selection)

short_candidates = [p for p in domain_samples if len(p["candidates"]) < SAMPLES_PER_DOMAIN]
print(f"Đã chọn {sum(len(p['candidates']) for p in domain_samples):,} URL ứng viên cho 97 domain.")
for spec in short_candidates:
    print(f"THIẾU URL: {spec['domain_id']} {spec['domain']} "
          f"chỉ có {len(spec['candidates'])}/{SAMPLES_PER_DOMAIN} ứng viên.")


Quét URL để chọn mẫu: 4394718URL [01:17, 56844.42URL/s]


Đã chọn 2,720 URL ứng viên cho 97 domain.
THIẾU URL: d092 ask.familydoctor.com.cn chỉ có 3/10 ứng viên.
THIẾU URL: d093 mega.vietnamplus.vn chỉ có 2/10 ứng viên.
THIẾU URL: d094 yanglao.familydoctor.com.cn chỉ có 2/10 ứng viên.
THIẾU URL: d095 special.vietnamplus.vn chỉ có 1/10 ứng viên.
THIẾU URL: d096 fk.99.com.cn chỉ có 1/10 ứng viên.
THIẾU URL: d097 ypk.familydoctor.com.cn chỉ có 1/10 ứng viên.


## 4. Cấu hình crawl và chuyển Markdown — giữ nguyên notebook gốc

Thứ tự ưu tiên vẫn là **protected → slow → fast**. Domain nằm trong cả hai
danh sách dùng protected như trước. Không thêm bộ lọc làm sạch mới.
Ba kết quả dùng cho đánh giá: `markdown` là đầu ra hiện tại;
`raw_markdown` và `fit_markdown` là hai bản trước/sau pruning để đối chiếu.

In [4]:
def first_metadata_value(metadata: dict, *keys):
    for key in keys:
        value = metadata.get(key)

        if isinstance(value, str) and value.strip():
            return value.strip()

    return None


In [5]:
from urllib.parse import urlparse, urlsplit

from crawl4ai import (
    AsyncWebCrawler,
    BrowserConfig,
    CacheMode,
    CrawlerRunConfig,
    MemoryAdaptiveDispatcher,
    RateLimiter,
)
from crawl4ai.content_filter_strategy import PruningContentFilterLXML
from crawl4ai.markdown_generation_strategy import DefaultMarkdownGenerator

browser_config = BrowserConfig(
    browser_type='chromium',
    headless=True,
    enable_stealth=True,
    user_agent_mode='random',
)

prune_filter = PruningContentFilterLXML(
    threshold=0.6,
    threshold_type='dynamic',
    min_word_threshold=25,
)

markdown_generator = DefaultMarkdownGenerator(
    content_source='cleaned_html',
    content_filter=prune_filter,
    options={'ignore_links': True, "ignore_images": True},
)

# Fast default for most URLs. Streaming lets us checkpoint each completed result.
fast_config = CrawlerRunConfig(
    stream=True,
    cache_mode=CacheMode.BYPASS,
    wait_until='domcontentloaded',
    page_timeout=45_000,
    delay_before_return_html=0.2,
    markdown_generator=markdown_generator,
    excluded_tags=["nav", "footer", "aside"],
)

# Expensive behavior is restricted to known protected domains.
protected_config = CrawlerRunConfig(
    url_matcher=lambda url: urlparse(url).netloc.lower().removeprefix('www.') in PROTECTED_DOMAINS,
    stream=True,
    cache_mode=CacheMode.BYPASS,
    magic=True,
    simulate_user=True,
    override_navigator=True,
    page_timeout=90_000,
    delay_before_return_html=3.0,
    max_retries=2,
    markdown_generator=markdown_generator,
    excluded_tags=["nav", "footer", "aside"],
)

slow_config = CrawlerRunConfig(
    url_matcher=lambda url: (
        urlparse(url).netloc
        .lower()
        .removeprefix("www.") in SLOW_DOMAINS
    ),

    stream=True,
    cache_mode=CacheMode.BYPASS,

    # Chỉ chờ server bắt đầu trả document,
    # không bắt buộc DOMContentLoaded phải hoàn tất.
    wait_until="commit",

    page_timeout=90_000,

    # Sau commit, đợi nội dung body thực sự xuất hiện.
    wait_for="""
        js:() => {
            return document.body
                && document.body.innerText
                && document.body.innerText.length > 500;
        }
    """,
    wait_for_timeout=30_000,
    delay_before_return_html=1.0,
    excluded_tags=["nav", "footer", "aside"],
    markdown_generator=markdown_generator,
)

crawl_configs = [
    protected_config,  # Anti-bot domains
    slow_config,       # Slow-loading domains
    fast_config,       # Default
]

def make_dispatcher():
    return MemoryAdaptiveDispatcher(
        memory_threshold_percent=MEMORY_THRESHOLD_PERCENT,
        max_session_permit=MAX_CONCURRENCY,
        rate_limiter=RateLimiter(
            base_delay=(0.2, 0.8),
            max_delay=20.0,
            max_retries=2,
        ),
    )

def markdown_text(markdown_result):
    if markdown_result is None:
        return ""

    if isinstance(markdown_result, str):
        return markdown_result

    raw = markdown_result.raw_markdown or ""
    fit = markdown_result.fit_markdown or ""

    # FIT chỉ chứa "word" lặp lại → dùng RAW.
    if fit.strip() and set(fit.split()) != {"word"}:
        return fit

    return raw

def url_identity(url: str) -> tuple[str, str, str]:
    parsed = urlsplit(url or '')
    host = parsed.netloc.lower().removeprefix('www.')
    path = parsed.path.rstrip('/') or '/'
    return host, path, parsed.query

def blocked_page_reason(title, markdown, status_code):
    title_text = (title or '').strip().lower()
    content = (markdown or '').strip().lower()
    if status_code in {403, 429, 503}:
        return f'http_{status_code}'
    blocked_titles = {'checking your browser...', 'just a moment...', 'access denied'}
    if title_text in blocked_titles:
        return 'anti_bot_challenge'
    markers = ('checking your browser', 'verify you are human', 'cf-chl-', 'captcha')
    if len(content) < 2_000 and any(marker in content for marker in markers):
        return 'anti_bot_challenge'
    return None

def crawl_result_to_record(result, requested_url: str) -> dict:
    status_code = getattr(result, 'status_code', None)
    redirected_url = getattr(result, 'redirected_url', None)
    final_url = redirected_url or getattr(result, 'url', None) or requested_url
    final_status_code = getattr(result, 'redirected_status_code', None) or status_code
    base = {
        'url': requested_url,
        'final_url': final_url,
        'domain': urlparse(final_url).netloc.lower(),
        'status_code': status_code,
        'final_status_code': final_status_code,
        'redirected': final_url != requested_url,
    }
    if not result.success:
        return {
            **base,
            'success': False,
            'error_type': 'crawl_error',
            'error': getattr(result, 'error_message', None) or 'Unknown crawl error',
        }

    metadata = getattr(result, 'metadata', None) or {}
    title = first_metadata_value(metadata, 'title', 'og:title', 'twitter:title')
    description = first_metadata_value(
        metadata, 'description', 'og:description', 'twitter:description'
    )
    keywords = first_metadata_value(metadata, 'keywords')
    markdown = markdown_text(getattr(result, 'markdown', None))
    blocked_reason = blocked_page_reason(title, markdown, final_status_code)

    if blocked_reason:
        return {
            **base,
            'title': title,
            'description': description,
            'keywords': keywords,
            'markdown': markdown,
            'success': False,
            'retryable': True,
            'error_type': blocked_reason,
            'error': 'Received an anti-bot or rate-limit page instead of article content.',
        }
    if not markdown.strip():
        return {
            **base,
            'title': title,
            'success': False,
            'retryable': True,
            'error_type': 'empty_content',
            'error': 'Crawl succeeded but produced no Markdown.',
        }
    return {
        **base,
        'title': title,
        'description': description,
        'keywords': keywords,
        'markdown': markdown,
        'success': True,
    }


## 5. Crawl tối đa 10 bài thành công mỗi domain và lưu checkpoint local

Browser đóng sau mỗi batch, như notebook gốc. Mỗi batch chỉ lấy số URL còn
thiếu nên không vượt quá 10 bài thành công/domain. Lỗi được giữ trong log và
dùng URL dự phòng tiếp theo; không thử vô hạn.

Checkpoint theo domain được ghi sau mỗi batch. Rerun cell tiếp tục từ những
URL chưa thử; không nối thêm dòng trùng. Nếu tắt máy trong một batch, chỉ batch
chưa được ghi có thể phải chạy lại. Khi đổi cấu hình crawl hoặc cập nhật
Crawl4AI, dùng `OUTPUT_DIR` mới để không trộn các thí nghiệm.

In [6]:
def markdown_diagnostics(result):
    value = getattr(result, "markdown", None)
    raw = value if isinstance(value, str) else (getattr(value, "raw_markdown", None) or "")
    fit = "" if isinstance(value, str) else (getattr(value, "fit_markdown", None) or "")
    use_fit = bool(fit.strip()) and set(fit.split()) != {"word"}
    source = "fit" if use_fit else ("raw" if raw else "empty")
    return {"raw_markdown": raw, "fit_markdown": fit, "markdown_source": source}

from collections import defaultdict, deque
from tqdm.auto import tqdm
import asyncio

def pending_lookup(batch):
    lookup = defaultdict(deque)
    for item in batch:
        lookup[url_identity(item['url'])].append(item)
    return lookup

def remaining_items(lookup):
    for queue in lookup.values():
        yield from queue

async def crawl_batch(crawler, dispatcher, batch, progress):
    records = []
    lookup = pending_lookup(batch)
    successes = errors = unmatched_results = 0

    try:
        result_stream = await crawler.arun_many(
            urls=[item['url'] for item in batch],
            config=crawl_configs,
            dispatcher=dispatcher,
        )

        async for crawl_result in result_stream:
            result_url = getattr(crawl_result, 'url', None) or ''
            queue = lookup.get(url_identity(result_url))
            if not queue:
                # Do not guess a doc_id when a returned URL cannot be mapped safely.
                unmatched_results += 1
                continue

            item = queue[0]
            doc_id = str(item['id'])
            record = crawl_result_to_record(crawl_result, item['url'])
            record['doc_id'] = doc_id
            record.update(markdown_diagnostics(crawl_result))
            queue.popleft()

            if record['success']:
                records.append(record)
                successes += 1
            else:
                records.append(record)
                errors += 1

            progress.update(1)

    except Exception as exc:
        batch_error = f'{type(exc).__name__}: {exc}'
        for item in remaining_items(lookup):
            doc_id = str(item['id'])
            record = {
                'doc_id': doc_id,
                'url': item['url'],
                'success': False,
                'retryable': True,
                'error_type': 'batch_error',
                'error': batch_error,
            }
            records.append(record)
            errors += 1
            progress.update(1)
        return records, successes, errors, unmatched_results

    # A missing/unmappable result is retried later instead of being linked to the wrong doc_id.
    for item in remaining_items(lookup):
        doc_id = str(item['id'])
        record = {
            'doc_id': doc_id,
            'url': item['url'],
            'success': False,
            'retryable': True,
            'error_type': 'unmapped_result',
            'error': 'arun_many returned no safely mappable result for this URL.',
        }
        records.append(record)
        errors += 1
        progress.update(1)

    return records, successes, errors, unmatched_results


CHECKPOINT_DIR = OUTPUT_DIR / "checkpoints"
CHECKPOINT_DIR.mkdir(exist_ok=True)

# Ghi cấu hình chính để không resume nhầm thư mục thí nghiệm.
config_fields = ("wait_until", "page_timeout", "delay_before_return_html", "magic",
                 "simulate_user", "override_navigator", "wait_for", "wait_for_timeout",
                 "max_retries", "excluded_tags")
run_settings = {"selection_sha256": hashlib.sha256(selection_path.read_bytes()).hexdigest(),
                "target_per_domain": SAMPLES_PER_DOMAIN,
                "crawl_configs": [{name: getattr(config, name, None) for name in config_fields}
                                  for config in crawl_configs],
                "pruning": {name: getattr(prune_filter, name, None)
                            for name in ("threshold", "threshold_type", "min_word_threshold")},
                "protected_domains": sorted(PROTECTED_DOMAINS),
                "slow_domains": sorted(SLOW_DOMAINS),
                "max_concurrency": MAX_CONCURRENCY,
                "memory_threshold_percent": MEMORY_THRESHOLD_PERCENT,
                "crawl4ai_version": version("crawl4ai")}
manifest_path = OUTPUT_DIR / "run_settings.json"
if manifest_path.exists():
    if json.loads(manifest_path.read_text(encoding="utf-8")) != run_settings:
        raise ValueError("Cấu hình crawl đã đổi. Dùng OUTPUT_DIR mới để chạy thí nghiệm mới.")
else:
    write_json(manifest_path, run_settings)

def checkpoint_path(spec):
    return CHECKPOINT_DIR / f"{spec['domain_id']}.json"

def read_attempts(spec):
    path = checkpoint_path(spec)
    return json.loads(path.read_text(encoding="utf-8")) if path.exists() else []

def export_outputs():
    # Tạo lại output từ checkpoint, luôn giữ phần đã crawl xong.
    summary = []
    dataset_path = OUTPUT_DIR / "dataset.jsonl"
    attempts_path = OUTPUT_DIR / "crawl_attempts.jsonl"
    dataset_temp = dataset_path.with_suffix(".jsonl.tmp")
    attempts_temp = attempts_path.with_suffix(".jsonl.tmp")
    with dataset_temp.open("w", encoding="utf-8") as dataset_file, \
         attempts_temp.open("w", encoding="utf-8") as attempts_file:
        for spec in domain_samples:
            attempts = read_attempts(spec)
            successes = [row for row in attempts if row["success"]]
            for row in attempts:
                attempts_file.write(json.dumps(row, ensure_ascii=False) + "\n")
            for index, row in enumerate(successes[:SAMPLES_PER_DOMAIN], 1):
                sample = {**row, "sample_id": f"{spec['domain_id']}_{index:02d}",
                          "sample_index": index}
                dataset_file.write(json.dumps(sample, ensure_ascii=False) + "\n")
            summary.append({"domain_id": spec["domain_id"],
                            "domain": spec["domain"],
                            "matched_source_rows": spec["matched_source_rows"],
                            "candidate_urls": len(spec["candidates"]),
                            "attempted": len(attempts), "successes": len(successes),
                            "errors": len(attempts) - len(successes),
                            "missing_samples": max(0, SAMPLES_PER_DOMAIN - len(successes)),
                            "untried_candidates": len(spec["candidates"]) - len(attempts)})
    dataset_temp.replace(dataset_path)
    attempts_temp.replace(attempts_path)
    with (OUTPUT_DIR / "domain_summary.csv").open("w", encoding="utf-8-sig", newline="") as f:
        writer = csv.DictWriter(f, fieldnames=list(summary[0]))
        writer.writeheader()
        writer.writerows(summary)
    return summary

async def run_sampling():
    progress = tqdm(desc="URL đã thử", unit="URL")
    try:
        for spec in domain_samples:
            attempts = read_attempts(spec)
            tried = {row["url"] for row in attempts}
            remaining = [item for item in spec["candidates"] if item["url"] not in tried]
            successes = sum(row["success"] for row in attempts)
            while successes < SAMPLES_PER_DOMAIN and remaining:
                needed = SAMPLES_PER_DOMAIN - successes
                batch, remaining = remaining[:needed], remaining[needed:]
                async with AsyncWebCrawler(config=browser_config) as crawler:
                    records, _, _, _ = await crawl_batch(crawler, make_dispatcher(), batch, progress)
                for row in records:
                    row.update({"domain_id": spec["domain_id"],
                                "sampled_domain": spec["domain"],
                                "crawled_at": datetime.now(timezone.utc).isoformat()})
                    for key in ("title", "description", "keywords", "status_code", "final_status_code"):
                        row.setdefault(key, None)
                    for key in ("markdown", "raw_markdown", "fit_markdown"):
                        row.setdefault(key, "")
                    row.setdefault("markdown_source", "empty")
                    row.setdefault("final_url", row["url"])
                    row.setdefault("domain", urlparse(row["final_url"]).netloc.lower())
                    row.setdefault("redirected", row["final_url"] != row["url"])
                    row.setdefault("error_type", None)
                    row.setdefault("error", None)
                    row["markdown_chars"] = len(row["markdown"])
                    row["raw_markdown_chars"] = len(row["raw_markdown"])
                    row["fit_markdown_chars"] = len(row["fit_markdown"])
                attempts.extend(records)
                successes = sum(row["success"] for row in attempts)
                write_json(checkpoint_path(spec), attempts)
                progress.set_postfix(domain=spec["domain_id"], ok=successes)
            export_outputs()
            tqdm.write(f"{spec['domain_id']} {spec['domain']}: "
                       f"{successes}/{SAMPLES_PER_DOMAIN} bài, {len(attempts)} lần thử")
    finally:
        progress.close()
        export_outputs()

await run_sampling()
summary_rows = export_outputs()
actual = sum(row["successes"] for row in summary_rows)
missing = sum(row["missing_samples"] for row in summary_rows)
print(f"Dataset: {actual:,}/{TARGET_ROWS:,} dòng thành công. Còn thiếu: {missing:,}.")
print("Output:", OUTPUT_DIR.resolve())


URL đã thử: 0URL [00:00, ?URL/s]

[INIT].... → Crawl4AI 0.9.4 

[FETCH]... ↓ http://www.cnkang.com/dzjk/201307/925155.html                                                        | ✓ | ⏱: 69.24s 

[SCRAPE].. ◆ http://www.cnkang.com/dzjk/201307/925155.html                                                        | ✓ | ⏱: 0.21s 

[COMPLETE] ● http://www.cnkang.com/dzjk/201307/925155.html                                                        | ✓ | ⏱: 69.55s 

...

[SCRAPE].. ◆ https://ypk.familydoctor.com.cn/267067/                                                              | ✓ | ⏱: 0.00s 

[ERROR]... × https://ypk.familydoctor.com.cn/267067/            | Error: Blocked by anti-bot protection: HTTP 403 with HTML content (1025 bytes) 

[COMPLETE] ● https://ypk.familydoctor.com.cn/267067/                                                              | ✗ | ⏱: 32.73s 

URL đã thử: 1462URL [6:40:38, 16.44s/URL, domain=d097, ok=0]


d097 ypk.familydoctor.com.cn: 0/10 bài, 1 lần thử
Dataset: 791/970 dòng thành công. Còn thiếu: 179.
Output: /Volumes/security/lucraft@lucraftmeds/lucraftmeds@notebooks/data-creation/reapeated-pattern-analysis/domain_cleanliness


## 6. Kiểm tra dataset và các domain thiếu mẫu

| File | Nội dung |
|---|---|
| `dataset.jsonl` | Tối đa 10 bài crawl thành công/domain; Markdown đầy đủ, không cắt ngắn |
| `crawl_attempts.jsonl` | Tất cả lần thử, gồm thành công và lỗi; dùng kiểm tra tỷ lệ crawl lỗi |
| `domain_summary.csv` | Số URL nguồn, ứng viên, lần thử, thành công, lỗi và số bài thiếu theo domain |
| `selected_urls.json` | URL thật đã chọn cùng `id` nguồn, có thể dùng lại |
| `run_settings.json` | Cấu hình và phiên bản Crawl4AI của lần chạy |

Mỗi dòng dataset có `domain_id`, `sampled_domain`, `sample_id`,
`doc_id`, URL gốc/cuối, HTTP status, title/description/keywords, `markdown`,
`raw_markdown`, `fit_markdown`, `markdown_source`, độ dài và thời điểm crawl.

Cho LLM đọc **`markdown`** để chấm đầu ra hiện tại; dùng RAW/FIT để điều tra khi
mất nội dung hoặc còn nhiều menu. Không chỉ đếm số dòng: kiểm tra tất cả domain
có đủ mẫu và đọc `crawl_attempts.jsonl` để tránh bỏ qua các domain khó crawl.
Các mẫu đã thành công là tập thiên về trang crawl được, không đại diện cho tỷ lệ
thành công của toàn bộ website. 10 mẫu/template chỉ là kiểm tra ban đầu; nếu bạn
điều chỉnh rule bằng những mẫu này, hãy kiểm tra lại với một bộ mẫu khác.

In [7]:
import pandas as pd
from itertools import islice

summary_df = pd.read_csv(OUTPUT_DIR / "domain_summary.csv")
display(summary_df)
shortages = summary_df[summary_df["missing_samples"] > 0]
if not shortages.empty:
    print("Các domain chưa đủ 10 bài:")
    display(shortages)

with (OUTPUT_DIR / "dataset.jsonl").open(encoding="utf-8") as f:
    sample_rows = [json.loads(line) for line in islice(f, 3)]
display(pd.DataFrame(sample_rows).drop(columns=["markdown", "raw_markdown", "fit_markdown"], errors="ignore"))
if sample_rows:
    print("Markdown mẫu đầu (chỉ preview 2.000 ký tự; file giữ nguyên toàn bộ):")
    print(sample_rows[0]["markdown"][:2000])


,domain_id,domain,matched_source_rows,candidate_urls,attempted,successes,errors,missing_samples,untried_candidates
0,d001,cnkang.com,963438,30,10,10,0,0,20
1,d002,120ask.com,918479,30,10,10,0,0,20
2,d003,familydoctor.com.cn,447453,30,30,0,30,10,0
3,d004,ask.39.net,337375,30,10,10,0,0,20
4,d005,zysjonline.com,243347,30,30,7,23,3,0
...,...,...,...,...,...,...,...,...,...
92,d093,mega.vietnamplus.vn,2,2,2,2,0,8,0
93,d094,yanglao.familydoctor.com.cn,2,2,2,0,2,10,0
94,d095,special.vietnamplus.vn,1,1,1,0,1,10,0
95,d096,fk.99.com.cn,1,1,1,1,0,9,0


Các domain chưa đủ 10 bài:


,domain_id,domain,matched_source_rows,candidate_urls,attempted,successes,errors,missing_samples,untried_candidates
2,d003,familydoctor.com.cn,447453,30,30,0,30,10,0
4,d005,zysjonline.com,243347,30,30,7,23,3,0
15,d016,baby.39.net,27621,30,30,8,22,2,0
18,d019,bingli.iiyi.com,24990,30,30,0,30,10,0
21,d022,jbk.39.net,19142,30,30,7,23,3,0
26,d027,care.39.net,15134,30,30,7,23,3,0
27,d028,test.pmphai.com,15120,30,30,7,23,3,0
30,d031,fitness.39.net,12066,30,30,7,23,3,0
34,d035,food.39.net,11024,30,30,7,23,3,0
36,d037,fk.39.net,9812,30,30,7,23,3,0


,url,final_url,domain,status_code,final_status_code,redirected,title,description,keywords,success,...,domain_id,sampled_domain,crawled_at,error_type,error,markdown_chars,raw_markdown_chars,fit_markdown_chars,sample_id,sample_index
0,http://www.cnkang.com/dzjk/201307/925155.html,https://www.cnkang.com/dzjk/201307/925155.html,www.cnkang.com,301,200,True,孕妇可以吃石榴吗_怀孕的孕妇可以吃石榴吗_中华康网,孕妇可以吃石榴吗，石榴颜色亮丽，口味酸甜，因此很多孕妇都爱吃石榴。那么孕妇可以吃石榴吗?下面...,"石榴,孕妇可以吃石榴吗",True,...,d001,cnkang.com,2026-10-10T10:06:41.047292+00:00,None,None,1437,1437,0,d001_01,1
1,http://www.cnkang.com/dise/264/925935.html,https://www.cnkang.com/dise/264/925935.html,www.cnkang.com,301,200,True,胰腺癌症状有哪些呢_中华康网,胰腺癌症状有哪些呢？胰腺癌患者表现出来的症状可能是不一样的，以及胰腺癌的生长部位等因素。但是...,胰腺癌症状有哪些呢,True,...,d001,cnkang.com,2026-10-10T10:06:41.047322+00:00,None,None,4114,4114,0,d001_02,2
2,http://www.cnkang.com/dise/174/67766.html,https://www.cnkang.com/dise/174/67766.html,www.cnkang.com,301,200,True,低血糖的饮食原则是怎样的_中华康网,功能性低血糖是低血糖的类型之一，而这种类型的低血糖有着其特殊性，它严重的时候可能会导致患者昏...,低血糖的饮食原则是怎样的,True,...,d001,cnkang.com,2026-10-10T10:06:41.047338+00:00,None,None,4419,4419,0,d001_03,3


Markdown mẫu đầu (chỉ preview 2.000 ký tự; file giữ nguyên toàn bộ):
|   |   
 |  男性 健身 | 休闲 | 保健 | 疾病 | 爱好 | 品味  
女性 美容 | 整形 | 减肥 | 职场 | 情感 | 育儿  |   |  健康 男科 | 妇科 | 疾病 | 外科 | 体检 | 食疗 | 心理  
生活 家居 | 旅游 | 养生 | 急救 | 解梦 | 星座 | 美食  |   |  医学药学 | 健康资讯  
中医中药 | 老人健康  |  
| --- | --- | --- | --- | --- |  
 |  
|   
 |   | 饮食健康知识  |   | 食材介绍  |   | 美食做法大全  |   | 糕点小吃做法  |   | 食疗作用功效  |   | 水果营养  |   | 其他美食  |  
| --- | --- | --- | --- | --- | --- | --- | --- | --- | --- | --- | --- | --- | --- |  
 |  
| 专题推荐： 老年疾病 生活技巧 家居用品 装修建材 家用电器 家庭药箱 外出旅游 局部减肥 心理疾病 眼眉整形 美食做法 食材大全 小吃做法 食疗功效 水果营养 饮食知识  |  
您的位置： 中华康网 >> 水果干果营养 >> 孕妇可以吃石榴吗
# 孕妇可以吃石榴吗
* * *  
|  www.cnkang.com 2013-7-19 本站原创   |   |  
| --- | --- |  
石榴颜色亮丽，口味酸甜，因此很多孕妇都爱吃石榴。那么孕妇可以吃石榴吗?下面就随康网小编一起看看孕妇可不可以吃石榴吧。
**孕妇可以吃石榴吗?**
石榴的营养特别丰富，含有多种人体所需的营养成分，果实中含有维生素C及B族维生素，有机酸、糖类、蛋白质、脂肪，以及钙、磷、钾等矿物质。其中维生素C的含量比苹果高1～2倍，而脂肪、蛋白质的含量较少，果实以品鲜为主。石榴具有生津化食，抗胃酸过多，软化血管、止泻、解毒、降温等多种功能。
因此，孕妇能吃石榴，而且孕妇吃石榴，对于自身和宝宝的好处都非常大。
**孕妇吃石榴的注意事项**
体寒的孕妇可以多吃些石榴，体热的孕妇不宜多吃。同时，吃任何水果，都

Tài liệu API đã đối chiếu:
[Crawl4AI arun_many](https://docs.crawl4ai.com/api/arun_many/),
[Crawl4AI cấu hình và thứ tự URL matcher](https://docs.crawl4ai.com/api/parameters/),
[Hugging Face streaming](https://huggingface.co/docs/datasets/en/stream).